In [0]:
print("Banking Data Engineering Project")

Banking Data Engineering Project


In [0]:
print("Spark Version",spark.version)

Spark Version 4.2.0


In [0]:
display(spark.sql("SHOW CATALOGS"))

catalog
samples
system
workspace


In [0]:
display(spark.sql("SHOW SCHEMAS IN workspace"))

databaseName
default
information_schema


In [0]:
%sql
CREATE VOLUME IF NOT EXISTS workspace.default.banking_data;

In [0]:
%sql
SHOW VOLUMES IN workspace.default

database,volume_name
default,banking_data


In [0]:
display(dbutils.fs.ls("/Volumes/workspace/default/banking_data/"))

path,name,size,modificationTime
dbfs:/Volumes/workspace/default/banking_data/accounts.csv,accounts.csv,4576052,1787989185000
dbfs:/Volumes/workspace/default/banking_data/bank.xlsx,bank.xlsx,6558230,1787989434000
dbfs:/Volumes/workspace/default/banking_data/branches.csv,branches.csv,25055,1787989215000
dbfs:/Volumes/workspace/default/banking_data/cards.csv,cards.csv,4949764,1787989403000
dbfs:/Volumes/workspace/default/banking_data/customers.csv,customers.csv,4048431,1787988955000
dbfs:/Volumes/workspace/default/banking_data/loans.csv,loans.csv,1734691,1787989306000
dbfs:/Volumes/workspace/default/banking_data/merchants.csv,merchants.csv,236937,1787989326000


In [0]:
customers_df = spark.read \
    .option("header", True) \
    .option("inferSechema",True)\
    .csv("/Volumes/workspace/default/banking_data/customers.csv")  
display(customers_df)         

customer_id,first_name,last_name,email,city,credit_score,created_at
CUSXAJI0Y6DPBHS,Kevin,Young,brauncameron@example.net,North Williamville,327,2025-04-17
CUSHXTHV3A3ZMF8,Jason,Clements,toddwilliam@example.net,Martinezside,644,2020-02-23
CUSDD4V30T9NT3W,Randy,Thompson,trevoranderson@example.org,Gallowayfurt,670,2025-06-22
CUSGCX1945NQ4FM,Laura,Phillips,valdezgeorge@example.com,Morrisview,573,2019-10-20
CUSVG0FN9XUY41I,Savannah,Swanson,smithluis@example.com,Lake Anna,332,2022-07-16
CUSOC6UZHR5XFF0,Ashley,Wang,reesekendra@example.com,Amybury,569,2025-07-22
CUSPVN9ER14FFYV,Morgan,Miller,narnold@example.org,New Javierbury,694,2023-04-13
CUSVQJT7YE511MK,David,Cabrera,heidi41@example.net,West Michelle,461,2024-02-02
CUSAZZ81SDW4SHN,Alicia,Rivera,debrawarren@example.com,West Laura,465,2025-01-18
CUS877VREN93IIU,Ashley,Hoffman,dstuart@example.org,South Jennifer,380,2019-12-17


In [0]:
customers_df.printSchema()
print("Total Rows:",customers_df.count())
print("Total Columns:",len(customers_df.columns))
print("Columns",customers_df.columns)

root
 |-- customer_id: string (nullable = true)
 |-- first_name: string (nullable = true)
 |-- last_name: string (nullable = true)
 |-- email: string (nullable = true)
 |-- city: string (nullable = true)
 |-- credit_score: string (nullable = true)
 |-- created_at: string (nullable = true)

Total Rows: 50000
Total Columns: 7
Columns ['customer_id', 'first_name', 'last_name', 'email', 'city', 'credit_score', 'created_at']


#### check null value


In [0]:
from pyspark.sql.functions import col, sum 
null_counts =customers_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in customers_df.columns
])
display(null_counts)


customer_id,first_name,last_name,email,city,credit_score,created_at
0,0,0,0,0,0,0


##### Check Dublicate 

In [0]:
dublicate_count =customers_df.count() -\
    customers_df.dropDuplicates(["customer_id"]).count()

print(dublicate_count)    

0


In [0]:
customers_df.select("credit_score") \
     .distinct() \
    .orderBy("credit_score") \
    .show(30)

+------------+
|credit_score|
+------------+
|         300|
|         301|
|         302|
|         303|
|         304|
|         305|
|         306|
|         307|
|         308|
|         309|
|         310|
|         311|
|         312|
|         313|
|         314|
|         315|
|         316|
|         317|
|         318|
|         319|
|         320|
|         321|
|         322|
|         323|
|         324|
|         325|
|         326|
|         327|
|         328|
|         329|
+------------+
only showing top 30 rows


In [0]:
from pyspark.sql.functions import col, min, max

credit_score_stats = customers_df.select(
    min(col("credit_score").cast("int")).alias("min_credit_score"),
    max(col("credit_score").cast("int")).alias("max_credit_score")
)

display(credit_score_stats)

min_credit_score,max_credit_score
300,850


In [0]:
invalid_credit_scores = customers_df.filter(
    (col("credit_score").cast("int") < 300) |
    (col("credit_score").cast("int") > 850)
)

print("Invalid credit score records:", invalid_credit_scores.count())

Invalid credit score records: 0


In [0]:
customers_df.select("created_at").show(20)

+----------+
|created_at|
+----------+
|2025-04-17|
|2020-02-23|
|2025-06-22|
|2019-10-20|
|2022-07-16|
|2025-07-22|
|2023-04-13|
|2024-02-02|
|2025-01-18|
|2019-12-17|
|2022-06-30|
|2021-07-26|
|2021-02-18|
|2021-02-18|
|2021-08-26|
|2020-09-26|
|2019-10-08|
|2022-07-10|
|2020-06-26|
|2020-02-29|
+----------+
only showing top 20 rows


In [0]:
from pyspark.sql.functions import col, to_date

invalid_dates = customers_df.filter(
    to_date(col("created_at"), "yyyy-MM-dd").isNull()
)

print("Invalid created_at records:", invalid_dates.count())

Invalid created_at records: 0


In [0]:
from pyspark.sql.functions import min, max

date_stats = customers_df.select(
    min(to_date("created_at", "yyyy-MM-dd")).alias("min_created_at"),
    max(to_date("created_at", "yyyy-MM-dd")).alias("max_created_at")
)

display(date_stats)

min_created_at,max_created_at
2019-01-01,2025-12-31


### Now Account CSV file check

In [0]:
accounts_df =spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/banking_data/accounts.csv")  
display(accounts_df)      

account_id,customer_id,account_type,balance_usd,open_date
ACCOD48PUCAEHKH,CUSAEOACKBH8CK6,Checking,182700.46,2021-03-27
ACCU2DMTSOYD5R6,CUSKI0ABUBGCLFD,Savings,57886.71,2019-10-21
ACCXFI6TF26FL9B,CUSWXG0ESCUG77M,Business,68774.44,2019-02-15
ACCJ6SUS4ZI6BRT,CUSUTT52LK3TW0J,Business,67015.68,2021-10-30
ACCNP7JE3AQW8TG,CUSNUWQT2EXWNSC,Savings,67265.67,2023-12-05
ACCDWXIMEPJEK1M,CUS9YL8T9J6JVFB,Savings,68975.59,2024-04-07
ACCZT96PKCU0WD9,CUSDMISW804XPRO,Business,180076.81,2021-12-19
ACCXTK5RZJLV6C4,CUSSI6L5SODYNTG,Savings,113502.83,2022-01-01
ACCEG7CN1W6R987,CUSBQNS6ND3E3D8,Checking,52092.2,2024-11-12
ACC44HPKAAOS2L0,CUSA9P9URVI8PJ6,Checking,164330.33,2025-09-29


In [0]:
accounts_df.printSchema()
print("Total Rows:", accounts_df.count())
print("Total Columns:", len(accounts_df.columns))
print("Columns:", accounts_df.columns)

root
 |-- account_id: string (nullable = true)
 |-- customer_id: string (nullable = true)
 |-- account_type: string (nullable = true)
 |-- balance_usd: double (nullable = true)
 |-- open_date: date (nullable = true)

Total Rows: 75000
Total Columns: 5
Columns: ['account_id', 'customer_id', 'account_type', 'balance_usd', 'open_date']


In [0]:
from pyspark.sql.functions import col, sum

null_counts_accounts = accounts_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in accounts_df.columns
])

display(null_counts_accounts)

account_id,customer_id,account_type,balance_usd,open_date
0,0,0,0,0


In [0]:
duplicate_accounts = accounts_df.count() - \
    accounts_df.dropDuplicates(["account_id"]).count()

print("Duplicate account_id:", duplicate_accounts)

Duplicate account_id: 0


In [0]:
accounts_df.select("account_type") \
    .distinct() \
    .orderBy("account_type") \
    .show(truncate=False)

+------------+
|account_type|
+------------+
|Business    |
|Checking    |
|Savings     |
+------------+



In [0]:
negative_balance = accounts_df.filter(
    col("balance_usd") < 0
)

print("Negative balance records:", negative_balance.count())

Negative balance records: 0


In [0]:
from pyspark.sql.functions import min, max, avg

balance_stats = accounts_df.select(
    min("balance_usd").alias("min_balance"),
    max("balance_usd").alias("max_balance"),
    avg("balance_usd").alias("avg_balance")
)

display(balance_stats)

min_balance,max_balance,avg_balance
13.2,199994.58,100181.72188093326


In [0]:
invalid_customer_ids = accounts_df.join(
    customers_df.select("customer_id").distinct(),
    on="customer_id",
    how="left_anti"
)

print(
    "Accounts with invalid customer_id:",
    invalid_customer_ids.count()
)

Accounts with invalid customer_id: 0


#### Branch data

In [0]:
branches_df = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/banking_data/branches.csv")

display(branches_df)      

branch_id,branch_name,manager_name
BRNJITQ446NVY1P,Davidberg Branch,Sergio Parker
BRNVXROZ3RRD54H,Sanderschester Branch,James Wilson
BRN6IUCH832B5CG,West Aprilchester Branch,Benjamin Smith
BRNQKSE7WVBUGTJ,Amyborough Branch,Kimberly Soto
BRNZDKYMIYBCVIN,Deborahbury Branch,Katie Martinez
BRNN4K27L0UC4ER,Markfurt Branch,Gregory Bond
BRN8ZQ15HQ0K01B,Halemouth Branch,Nathan Bell
BRNH99UE75DQ5EH,North Georgeville Branch,Rita Smith
BRNH6M953T62YXX,Port Alexandria Branch,Ryan Benson
BRN88K8L50OCCHR,Pattersonfort Branch,Nancy Wells


In [0]:
branches_df.printSchema()
print("Total Rows:", branches_df.count())
print("Total Columns:", len(branches_df.columns))
print("Columns:", branches_df.columns)


root
 |-- branch_id: string (nullable = true)
 |-- branch_name: string (nullable = true)
 |-- manager_name: string (nullable = true)

Total Rows: 500
Total Columns: 3
Columns: ['branch_id', 'branch_name', 'manager_name']


In [0]:
null_counts =branches_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in branches_df.columns
])
display(null_counts)

branch_id,branch_name,manager_name
0,0,0


In [0]:
dublicate_branches =branches_df.count()- \
    branches_df.dropDuplicates(["branch_id"]).count()

print("Duplicate branch_id:", dublicate_branches)

Duplicate branch_id: 0


In [0]:
print("Total unique branch_id:", branches_df.select("branch_id").distinct().count())

Total unique branch_id: 500


In [0]:
duplicate_branch_names = branches_df.groupBy("branch_name") \
    .count() \
    .filter(col("count") > 1)

display(duplicate_branch_names)

branch_name,count
Hillmouth Branch,2
East Tammy Branch,2
New Justinshire Branch,2
New David Branch,3
South Holly Branch,2


#### Load Data

In [0]:
loans_df = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/banking_data/loans.csv")

display(loans_df)



loan_id,customer_id,loan_amount,interest_rate,start_date
LONVIJLFE0FQERD,CUS0VWWKGL3C2ET,7939.97,8.16,2024-05-05
LONHREM3GBFRZCN,CUSK3SW6KH12S96,176269.07,3.84,2022-12-12
LONRVF09SWTR92A,CUS7D2AZQQGCDHI,193167.37,10.97,2024-06-01
LONVIO8NY2TPJ97,CUSKF0P22H7PUEM,15623.54,13.35,2020-02-21
LON8MO4Z8F2MY71,CUS4KVHY58PGUXF,50695.04,7.37,2019-04-25
LONHDREEA5JR90K,CUS7BPAAKLYYY42,196049.13,8.1,2024-08-02
LONWR67XXRBBG9E,CUSJ7KYVHT6ZWCH,23074.9,7.08,2024-07-07
LONR1E6D7SHGHKT,CUSFY357STKLGR8,174356.26,5.26,2020-07-20
LON1ISOKTAMO1RT,CUSXOL4RMHAJ3F0,178071.99,2.75,2025-08-16
LONXSCBS1P2LLGW,CUSIUFWOFRYTP4D,272416.83,7.54,2019-03-29


In [0]:
loans_df.printSchema()
print("Total Rows:",loans_df.count())
print("Total Columns:",len(loans_df.columns))
print("Columns:",loans_df.columns)
null_counts_loans =loans_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in loans_df.columns
])
display(null_counts_loans)


root
 |-- loan_id: string (nullable = true)
 |-- customer_id: string (nullable = true)
 |-- loan_amount: double (nullable = true)
 |-- interest_rate: double (nullable = true)
 |-- start_date: date (nullable = true)

Total Rows: 30000
Total Columns: 5
Columns: ['loan_id', 'customer_id', 'loan_amount', 'interest_rate', 'start_date']


loan_id,customer_id,loan_amount,interest_rate,start_date
0,0,0,0,0


In [0]:
duplicate_loans = loans_df.count() - \
    loans_df.dropDuplicates(["loan_id"]).count()

print("Duplicate loan_id:", duplicate_loans)

Duplicate loan_id: 0


In [0]:
invalid_loan_customers = loans_df.join(
    customers_df.select("customer_id").distinct(),
    on="customer_id",
    how="left_anti"
)

print(
    "Loans with invalid customer_id:",
    invalid_loan_customers.count()
)

Loans with invalid customer_id: 0


In [0]:
negative_loans = loans_df.filter(
    col("loan_amount") < 0
)

print("Negative loan amount records:", negative_loans.count())

Negative loan amount records: 0


In [0]:
invalid_interest = loans_df.filter(
    (col("interest_rate") < 0) |
    (col("interest_rate") > 100)
)

print("Invalid interest rate records:", invalid_interest.count())

Invalid interest rate records: 0


In [0]:
from pyspark.sql.functions import min, max, avg

loan_stats = loans_df.select(
    min("loan_amount").alias("min_loan_amount"),
    max("loan_amount").alias("max_loan_amount"),
    avg("loan_amount").alias("avg_loan_amount"),
    min("interest_rate").alias("min_interest_rate"),
    max("interest_rate").alias("max_interest_rate")
)

display(loan_stats)

min_loan_amount,max_loan_amount,avg_loan_amount,min_interest_rate,max_interest_rate
1010.16,299975.47,150089.0166033332,2.0,15.0


#### merchants data

In [0]:
merchants_df = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/banking_data/merchants.csv")

display(merchants_df)

merchant_id,merchant_name,city
MERU9JCGLS9MNLI,"Williams, Moore and Campbell",West Bradley
MER43QNBEL8JWEW,Wolf LLC,New Heather
MER3N5P7AWGR7U5,Smith and Sons,Lake Kevinbury
MERLXSBZNU5LYTU,Barnes-Roberts,Port Grantfort
MERT7OA8XC77HJ1,Williamson-Contreras,West Dianaview
MERPAMYV4SYG8KK,Cole Group,Port Briantown
MER8QQVJD1FTCWC,Montgomery-Larsen,Lake Patriciaborough
MERMJNO5ZJIG56Y,Gomez-Foster,New Michael
MERUUA2FSWYI9UD,"Jackson, Knight and Miller",Port Justin
MER0JMGLEH597T8,Meyer and Sons,Rebeccaport


In [0]:
merchants_df.printSchema()

root
 |-- merchant_id: string (nullable = true)
 |-- merchant_name: string (nullable = true)
 |-- city: string (nullable = true)



In [0]:
print("Total Rows:", merchants_df.count())

Total Rows: 5000


In [0]:
null_counts_merchants = merchants_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in merchants_df.columns
])

display(null_counts_merchants)

merchant_id,merchant_name,city
0,0,0


In [0]:
duplicate_merchants = merchants_df.count() - \
    merchants_df.dropDuplicates(["merchant_id"]).count()

print("Duplicate merchant_id:", duplicate_merchants)

Duplicate merchant_id: 0


In [0]:
duplicate_merchant_names = merchants_df.groupBy("merchant_name") \
    .count() \
    .filter(col("count") > 1)

display(duplicate_merchant_names)

merchant_name,count
Hernandez Group,4
Campbell and Sons,3
Walsh Ltd,2
Rodriguez PLC,5
Brown Inc,4
Henderson Group,2
Anderson Group,3
Lee LLC,2
Miller Group,2
Gonzales Ltd,2


#### Cards Data

In [0]:
cards_df = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/banking_data/cards.csv")

display(cards_df)

card_id,account_id,card_type,expiration_date
CRD9DMMMTJDQT3V,ACC32AXBRYBVYAR,Debit,2032-02-07
CRD94590WYP462W,ACC2WKDTIPM83SK,Credit,2030-03-14
CRDB79THXNR6SGQ,ACCPZTJ2AUNVBRX,Credit,2026-12-17
CRDG81QQ58532B9,ACCV78E7JOA2O54,Debit,2029-10-21
CRD7RTUV3VVPJ60,ACCS8PHD7QLVC4L,Credit,2028-02-05
CRDV7L5SGAX2NFN,ACCRTI0QB8SGMN7,Debit,2029-01-17
CRDBB3GBBY3NO24,ACC21DY2JK3VXZM,Credit,2027-06-08
CRDG47ST4S3TPWT,ACCPX62AB27CICC,Credit,2030-01-22
CRDLNUHITN6T0NH,ACCQJ5QJXSLNR83,Debit,2030-11-05
CRDZIWYPTVT8SQQ,ACC4CRGBNY9WQTQ,Debit,2028-03-11


In [0]:
cards_df.printSchema()
print("Total Rows:", cards_df.count())
print("Totals columns:",cards_df.columns)


root
 |-- card_id: string (nullable = true)
 |-- account_id: string (nullable = true)
 |-- card_type: string (nullable = true)
 |-- expiration_date: date (nullable = true)

Total Rows: 100000
Totals columns: ['card_id', 'account_id', 'card_type', 'expiration_date']


In [0]:
from pyspark.sql.functions import col, sum

null_counts_cards = cards_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in cards_df.columns
])

display(null_counts_cards)

card_id,account_id,card_type,expiration_date
0,0,0,0


In [0]:
duplicate_cards = cards_df.count() - \
    cards_df.dropDuplicates(["card_id"]).count()

print("Duplicate card_id:", duplicate_cards)

Duplicate card_id: 0


In [0]:
accounts_df = spark.read \
    .option("header", True) \
    .option("inferSchema", True) \
    .csv("/Volumes/workspace/default/banking_data/accounts.csv")

In [0]:
invalid_card_accounts = cards_df.join(
    accounts_df.select("account_id").distinct(),
    on="account_id",
    how="left_anti"
)

print(
    "Cards with invalid account_id:",
    invalid_card_accounts.count()
)

Cards with invalid account_id: 0


In [0]:
duplicate_cards = cards_df.count() - \
    cards_df.dropDuplicates(["card_id"]).count()

print("Duplicate card_id:", duplicate_cards)

Duplicate card_id: 0


In [0]:
invalid_card_accounts = cards_df.join(
    accounts_df.select("account_id").distinct(),
    on="account_id",
    how="left_anti"
)

print(
    "Cards with invalid account_id:",
    invalid_card_accounts.count()
)

Cards with invalid account_id: 0


In [0]:
cards_df.select("card_type") \
    .distinct() \
    .orderBy("card_type") \
    .show(truncate=False)

+---------+
|card_type|
+---------+
|Credit   |
|Debit    |
+---------+



In [0]:
from pyspark.sql.functions import min, max

card_date_stats = cards_df.select(
    min("expiration_date").alias("min_expiration_date"),
    max("expiration_date").alias("max_expiration_date")
)

display(card_date_stats)

min_expiration_date,max_expiration_date
2025-01-01,2032-12-31


### Bank Details

In [0]:
%pip install openpyxl

Looking in indexes: [REDACTED]
Note: you may need to restart the kernel using %restart_python or dbutils.library.restartPython() to use updated packages.


In [0]:
import pandas as pd

bank_pd = pd.read_excel(
    "/Volumes/workspace/default/banking_data/bank.xlsx",
    engine="openpyxl"
)

display(bank_pd.head())

Account No,DATE,TRANSACTION DETAILS,CHQ.NO.,VALUE DATE,WITHDRAWAL AMT,DEPOSIT AMT,BALANCE AMT,.
409000611074',2017-06-29T00:00:00.000Z,TRF FROM Indiaforensic SERVICES,null,2017-06-29T00:00:00.000Z,null,1000000.0,1000000.0,.
409000611074',2017-07-05T00:00:00.000Z,TRF FROM Indiaforensic SERVICES,null,2017-07-05T00:00:00.000Z,null,1000000.0,2000000.0,.
409000611074',2017-07-18T00:00:00.000Z,FDRL/INTERNAL FUND TRANSFE,null,2017-07-18T00:00:00.000Z,null,500000.0,2500000.0,.
409000611074',2017-08-01T00:00:00.000Z,TRF FRM Indiaforensic SERVICES,null,2017-08-01T00:00:00.000Z,null,3000000.0,5500000.0,.
409000611074',2017-08-16T00:00:00.000Z,FDRL/INTERNAL FUND TRANSFE,null,2017-08-16T00:00:00.000Z,null,500000.0,6000000.0,.


In [0]:
print("Total Rows:", len(bank_pd))
print("Total Columns:", len(bank_pd.columns))
print("Columns:", bank_pd.columns.tolist())

Total Rows: 116201
Total Columns: 9
Columns: ['Account No', 'DATE', 'TRANSACTION DETAILS', 'CHQ.NO.', 'VALUE DATE', 'WITHDRAWAL AMT', 'DEPOSIT AMT', 'BALANCE AMT', '.']


In [0]:
# Convert all columns to string first
bank_pd = bank_pd.astype(str)

# Create Spark DataFrame
bank_df = spark.createDataFrame(bank_pd)

display(bank_df)

Account No,DATE,TRANSACTION DETAILS,CHQ.NO.,VALUE DATE,WITHDRAWAL AMT,DEPOSIT AMT,BALANCE AMT,.
409000611074',2017-06-29,TRF FROM Indiaforensic SERVICES,nan,2017-06-29,nan,1000000.0,1000000.0,.
409000611074',2017-07-05,TRF FROM Indiaforensic SERVICES,nan,2017-07-05,nan,1000000.0,2000000.0,.
409000611074',2017-07-18,FDRL/INTERNAL FUND TRANSFE,nan,2017-07-18,nan,500000.0,2500000.0,.
409000611074',2017-08-01,TRF FRM Indiaforensic SERVICES,nan,2017-08-01,nan,3000000.0,5500000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,6000000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,6500000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,7000000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,7500000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,8000000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,8500000.0,.


In [0]:
bank_df.printSchema()

root
 |-- Account No: string (nullable = true)
 |-- DATE: string (nullable = true)
 |-- TRANSACTION DETAILS: string (nullable = true)
 |-- CHQ.NO.: string (nullable = true)
 |-- VALUE DATE: string (nullable = true)
 |-- WITHDRAWAL AMT: string (nullable = true)
 |-- DEPOSIT AMT: string (nullable = true)
 |-- BALANCE AMT: string (nullable = true)
 |-- .: string (nullable = true)



In [0]:
bank_df = bank_df.toDF(
    "account_no",
    "transaction_date",
    "transaction_details",
    "cheque_no",
    "value_date",
    "withdrawal_amt",
    "deposit_amt",
    "balance_amt",
    "extra_column"
)

display(bank_df)

account_no,transaction_date,transaction_details,cheque_no,value_date,withdrawal_amt,deposit_amt,balance_amt,extra_column
409000611074',2017-06-29,TRF FROM Indiaforensic SERVICES,nan,2017-06-29,nan,1000000.0,1000000.0,.
409000611074',2017-07-05,TRF FROM Indiaforensic SERVICES,nan,2017-07-05,nan,1000000.0,2000000.0,.
409000611074',2017-07-18,FDRL/INTERNAL FUND TRANSFE,nan,2017-07-18,nan,500000.0,2500000.0,.
409000611074',2017-08-01,TRF FRM Indiaforensic SERVICES,nan,2017-08-01,nan,3000000.0,5500000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,6000000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,6500000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,7000000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,7500000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,8000000.0,.
409000611074',2017-08-16,FDRL/INTERNAL FUND TRANSFE,nan,2017-08-16,nan,500000.0,8500000.0,.


In [0]:
print(bank_df.columns)

['account_no', 'transaction_date', 'transaction_details', 'cheque_no', 'value_date', 'withdrawal_amt', 'deposit_amt', 'balance_amt', 'extra_column']


In [0]:
bank_df.printSchema()

root
 |-- account_no: string (nullable = true)
 |-- transaction_date: string (nullable = true)
 |-- transaction_details: string (nullable = true)
 |-- cheque_no: string (nullable = true)
 |-- value_date: string (nullable = true)
 |-- withdrawal_amt: string (nullable = true)
 |-- deposit_amt: string (nullable = true)
 |-- balance_amt: string (nullable = true)
 |-- extra_column: string (nullable = true)



In [0]:
bank_df = bank_df.toDF(
    "account_no",
    "transaction_date",
    "transaction_details",
    "cheque_no",
    "value_date",
    "withdrawal_amt",
    "deposit_amt",
    "balance_amt",
    "extra_column"
)

In [0]:
bank_df.printSchema()

root
 |-- account_no: string (nullable = true)
 |-- transaction_date: string (nullable = true)
 |-- transaction_details: string (nullable = true)
 |-- cheque_no: string (nullable = true)
 |-- value_date: string (nullable = true)
 |-- withdrawal_amt: string (nullable = true)
 |-- deposit_amt: string (nullable = true)
 |-- balance_amt: string (nullable = true)
 |-- extra_column: string (nullable = true)



In [0]:
from pyspark.sql.functions import col, sum

null_counts_bank = bank_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in bank_df.columns
])

display(null_counts_bank)

account_no,transaction_date,transaction_details,cheque_no,value_date,withdrawal_amt,deposit_amt,balance_amt,extra_column
0,0,0,0,0,0,0,0,0


In [0]:
from pyspark.sql.functions import trim

empty_counts_bank = bank_df.select([
    sum(
        (col(c).isNull() | (trim(col(c)) == "")).cast("int")
    ).alias(c)
    for c in bank_df.columns
])

display(empty_counts_bank)

account_no,transaction_date,transaction_details,cheque_no,value_date,withdrawal_amt,deposit_amt,balance_amt,extra_column
0,0,0,0,0,0,0,0,0


In [0]:
duplicate_bank_rows = bank_df.count() - \
    bank_df.dropDuplicates().count()

print("Duplicate complete rows:", duplicate_bank_rows)

Duplicate complete rows: 39


In [0]:
bank_silver_df = bank_df.dropDuplicates()

print("Bronze rows:", bank_df.count())
print("Silver rows:", bank_silver_df.count())

Bronze rows: 116201
Silver rows: 116162


In [0]:
from pyspark.sql.functions import col, when, lower, trim

bank_silver_df = bank_silver_df.select([
    when(
        lower(trim(col(c))).isin("nan", "null", ""),
        None
    ).otherwise(col(c)).alias(c)
    for c in bank_silver_df.columns
])

In [0]:
from pyspark.sql.functions import sum

null_counts_bank = bank_silver_df.select([
    sum(col(c).isNull().cast("int")).alias(c)
    for c in bank_silver_df.columns
])

display(null_counts_bank)

account_no,transaction_date,transaction_details,cheque_no,value_date,withdrawal_amt,deposit_amt,balance_amt,extra_column
0,0,2499,115257,0,62637,53525,0,0


In [0]:
display(
    bank_silver_df.select("extra_column")
    .distinct()
)

extra_column
.
